# Camada Bronze — CineData Analytics

Este notebook realiza a ingestão dos dados brutos para a camada Bronze da arquitetura Medalhão.

Boas práticas adotadas:
- criação do database Bronze caso ainda não exista;
- parametrização do período da API por widgets;
- ingestão dos CSVs sem transformação de conteúdo;
- inclusão somente da coluna `ingestion_datetime`;
- gravação em Delta no modo `append`;
- validação da resposta da API;
- mapeamento centralizado entre arquivos e tabelas;
- validação das tabelas após a ingestão.


In [0]:
# Imports utilizados no notebook
from datetime import date, timedelta

import pandas as pd
import requests

from pyspark.sql.functions import current_timestamp


In [0]:
# Configuração da camada Bronze
bronze_schema = "bronze"

# Cria o database caso ainda não exista.
spark.sql(f"CREATE DATABASE IF NOT EXISTS {bronze_schema}")

# Caminho do Volume onde estão os arquivos da pasta Inputs.
# Substitua pelos valores correspondentes ao seu ambiente Databricks.
volume_path = "/Volumes/<catalog>/<schema>/<volume>/Inputs"


In [0]:
# Widgets para parametrizar o período consultado na API.
# O período padrão corresponde aos últimos 7 dias corridos.
dbutils.widgets.text(
    "data_inicio",
    (date.today() - timedelta(days=7)).strftime("%m-%d-%Y"),
    "Data início (MM-DD-AAAA)"
)

dbutils.widgets.text(
    "data_fim",
    date.today().strftime("%m-%d-%Y"),
    "Data fim (MM-DD-AAAA)"
)

data_inicio_formatada = dbutils.widgets.get("data_inicio")
data_fim_formatada = dbutils.widgets.get("data_fim")

print(f"Período consultado: {data_inicio_formatada} até {data_fim_formatada}")


Período consultado: 09-30-2026 até 10-07-2026


## 1. Ingestão dos arquivos CSV

Na camada Bronze, os arquivos são armazenados sem alterações de conteúdo ou estrutura. A única coluna adicionada é `ingestion_datetime`, que registra o momento da ingestão.


In [0]:
# Mapeamento dos arquivos originais para as tabelas Bronze.
arquivos_bronze = {
    "movies_info_TMDB_IMDB.csv": "tb_movies_info",
    "movies_financials_IMDB_TMDB.csv": "tb_movies_financials",
    "movies_metrics_IMDB_TMDB.csv": "tb_movies_metrics",
    "credits_and_tags_IMDB_TMDB.csv": "tb_credits_and_tags",
    "movies_reviews.csv": "tb_movies_reviews"
}


In [0]:
# Ingere cada CSV na respectiva tabela Delta.
# Nenhuma limpeza, renomeação ou transformação de conteúdo é realizada nesta camada.
for arquivo, tabela in arquivos_bronze.items():
    caminho_arquivo = f"/Volumes/workspace/default/aula2/{arquivo}"

    df = (
        spark.read
        .option("header", True)
        .option("inferSchema", True)
        .csv(caminho_arquivo)
    )

    # Registra o momento da ingestão em cada registro.
    df_bronze = df.withColumn(
        "ingestion_datetime",
        current_timestamp()
    )

    (
        df_bronze.write
        .format("delta")
        .mode("overwrite") 
        .option("overwriteSchema", "true")
        .saveAsTable(f"{bronze_schema}.{tabela}")
    )

    print(f"Tabela sobrescrita com sucesso: {bronze_schema}.{tabela}")


Tabela sobrescrita com sucesso: bronze.tb_movies_info
Tabela sobrescrita com sucesso: bronze.tb_movies_financials
Tabela sobrescrita com sucesso: bronze.tb_movies_metrics
Tabela sobrescrita com sucesso: bronze.tb_credits_and_tags
Tabela sobrescrita com sucesso: bronze.tb_movies_reviews


## 2. Ingestão da cotação do dólar

A cotação é obtida pela API PTAX do Banco Central. São armazenadas as colunas `dataHoraCotacao` e `cotacaoCompra`, além de `ingestion_datetime`.


In [0]:
# Endpoint da API PTAX do Banco Central.
url = (
    "https://olinda.bcb.gov.br/olinda/servico/PTAX/versao/v1/odata/"
    "CotacaoDolarPeriodo(dataInicial=@dataInicial,dataFinalCotacao=@dataFinalCotacao)"
    f"?@dataInicial='{data_inicio_formatada}'&@dataFinalCotacao='{data_fim_formatada}'"
    "&$select=dataHoraCotacao,cotacaoCompra&$format=json"
)

# Realiza a requisição com timeout para evitar espera indefinida.
resposta = requests.get(url, timeout=30)
resposta.raise_for_status()

cotacoes = resposta.json()["value"]

# A API pode não retornar cotações em finais de semana e feriados.
if not cotacoes:
    raise ValueError(
        "A API não retornou cotações para o período informado. "
        "Ajuste as datas nos widgets."
    )


In [0]:
# Converte a resposta da API para DataFrame Spark.
df_cotacao_raw = spark.createDataFrame(pd.DataFrame(cotacoes))

# Adiciona o timestamp de ingestão e grava os dados em Delta.
(
    df_cotacao_raw
    .withColumn("ingestion_datetime", current_timestamp())
    .write
    .format("delta")
    .mode("append")
    .saveAsTable(f"{bronze_schema}.tb_cotacao_dolar")
)

print(f"Ingestão concluída: API PTAX -> {bronze_schema}.tb_cotacao_dolar")


Ingestão concluída: API PTAX -> bronze.tb_cotacao_dolar


## 3. Validação da ingestão

Exibe as tabelas Bronze para verificar se os dados foram persistidos corretamente.


In [0]:
# Tabelas esperadas na camada Bronze.
tabelas_bronze = [
    "tb_movies_info",
    "tb_movies_financials",
    "tb_movies_metrics",
    "tb_credits_and_tags",
    "tb_movies_reviews",
    "tb_cotacao_dolar"
]

for tabela in tabelas_bronze:
    print(f"===== {bronze_schema}.{tabela} =====")
    display(
        spark.table(f"{bronze_schema}.{tabela}")
    )


===== bronze.tb_movies_info =====


id,tconst,title,original_title,original_language,release_date,runtime,status,overview,tagline,ingestion_datetime
293660,tt1431045,Deadpool,Deadpool,en,2016-02-09,108,Released,"The origin story of former Special Forces operative turned mercenary Wade Wilson, who, after being subjected to a rogue experiment that leaves him with accelerated healing powers, adopts the alter ego Deadpool. Armed with his new abilities and a dark, twisted sense of humor, Deadpool hunts down the man who nearly destroyed his life.",Witness the beginning of a happy ending.,2026-10-07T18:14:03.407Z
299536,tt4154756,AVENGERS: INFINITY WAR,Avengers: Infinity War,en,04-25-2018,149,Released,"As the Avengers and their allies have continued to protect the world from threats too large for any one hero to handle, a new danger has emerged from the cosmic shadows: Thanos. A despot of intergalactic infamy, his goal is to collect all six Infinity Stones, artifacts of unimaginable power, and use them to inflict his twisted will on all of reality. Everything the Avengers have fought for has led up to this moment - the fate of Earth and existence itself has never been more uncertain.",An entire universe. Once and for all.,2026-10-07T18:14:03.407Z
299534,tt4154796,Avengers: Endgame,Avengers: Endgame,en,2019-04-24,181,released,"After the devastating events of Avengers: Infinity War, the universe is in ruins due to the efforts of the Mad Titan, Thanos. With the help of remaining allies, the Avengers must assemble once more in order to undo Thanos' actions and restore order to the universe once and for all, no matter what consequences may be in store.",Avenge the fallen.,2026-10-07T18:14:03.407Z
475557,tt7286456,Joker,Joker,en,2019-10-01,122,Released,"During the 1980s, a failed stand-up comedian is driven insane and turns to a life of crime and chaos in Gotham City while becoming an infamous psychopathic crime figure.",Put on a happy face.,2026-10-07T18:14:03.407Z
271110,tt3498820,Captain America: Civil War,Captain America: Civil War,en,2016-04-27,147,Released,"Following the events of Age of Ultron, the collective governments of the world pass an act designed to regulate all superhuman activity. This polarizes opinion amongst the Avengers, causing two factions to side with Iron Man or Captain America, which causes an epic battle between former allies.",United we stand. Divided we fall.,2026-10-07T18:14:03.407Z
284054,tt1825683,Black Panther,Black Panther,en,2018-02-13,135,Released,"King T'Challa returns home to the reclusive, technologically advanced African nation of Wakanda to serve as his country's new leader. However, T'Challa soon finds that he is challenged for the throne by factions within his own country as well as without. Using powers reserved to Wakandan kings, T'Challa assumes the Black Panther mantle to join with ex-girlfriend Nakia, the queen-mother, his princess-kid sister, members of the Dora Milaje (the Wakandan 'special forces') and an American secret agent, to prevent Wakanda from being dragged into a world war.",null,2026-10-07T18:14:03.407Z
284052,tt1211837,Doctor Strange,Doctor Strange,en,2016-10-25,115,Released,"After his career is destroyed, a brilliant but arrogant surgeon gets a new lease on life when a sorcerer takes him under her wing and trains him to defend the world against evil.",The impossibilities are endless.,2026-10-07T18:14:03.407Z
315635,tt2250912,Spider-Man: Homecoming,Spider-Man: Homecoming,en,2017-07-05,133,RELEASED,"Following the events of Captain America: Civil War, Peter Parker, with the help of his mentor Tony Stark, tries to balance his life as an ordinary high school student in Queens, New York City, with fighting crime as his superhero alter ego Spider-Man as a new threat, the Vulture, emerges.",Homework can wait. The city can't.,2026-10-07T18:14:03.407Z
283995,tt3896198,Guardians of the Galaxy Vol. 2,Guardians of the Galaxy Vol. 2,en,2017-04-19,137,Released,The Guardians must fight to keep their newfound family together as t

===== bronze.tb_movies_financials =====


id,budget,revenue,ingestion_datetime
293660,58000000,Unknown,2026-10-07T18:14:08.477Z
299536,300000000,2052415039,2026-10-07T18:14:08.477Z
299534,356000000,2800000000,2026-10-07T18:14:08.477Z
475557,55000000,1074458282,2026-10-07T18:14:08.477Z
271110,250000000,Não Informado,2026-10-07T18:14:08.477Z
284054,200000000,1349926083,2026-10-07T18:14:08.477Z
284052,180000000,676343174,2026-10-07T18:14:08.477Z
315635,175000000,880166924,2026-10-07T18:14:08.477Z
283995,200000000,863756051,2026-10-07T18:14:08.477Z
297761,175000000,746846894,2026-10-07T18:14:08.477Z


===== bronze.tb_movies_metrics =====


...

id,genres,production_companies,production_countries,spoken_languages,keywords,directors,writers,cast,ingestion_datetime
293660,"Action, Adventure, Comedy","20th Century Fox, The Donners' Company, Genre Films",United States of America,English,"superhero, anti hero, mercenary, based on comic, aftercreditsstinger, duringcreditsstinger",Tim Miller,"Rhett Reese, Paul Wernick","Ryan Reynolds, Morena Baccarin, Ed Skrein, T.J. Miller, Gina Carano, Leslie Uggams, Brianna Hildebrand, Stefan Kapičić, Karan Soni, Randal Reeder",2026-10-07T18:14:16.282Z
299536,"Adventure, Action, Science Fiction",Marvel Studios,United States of America,"English, Xhosa","sacrifice, magic, superhero, based on comic, space, battlefield, genocide, magical object, super power, aftercreditsstinger, marvel cinematic universe (mcu), cosmic","Anthony Russo, Joe Russo",N/A,"Robert Downey Jr., Chris Evans, Chris Hemsworth, Josh Brolin, Mark Ruffalo, Scarlett Johansson, Don Cheadle, Benedict Cumberbatch, Tom Holland, Chadwick Boseman",2026-10-07T18:14:16.282Z
299534,"Adventure, Science Fiction, Action",Marvel Studios,United States of America,"English, Japanese, Xhosa","superhero, time travel, space travel, time machine, based on comic, sequel, alien invasion, superhero team, marvel cinematic universe (mcu), alternate timeline, father daughter relationship, sister sister relationship","Anthony Russo, Joe Russo","Christopher Markus, Stephen McFeely, Stan Lee, Jack Kirby, Joe Simon, Steve Englehart, Steve Gan, Bill Mantlo, Keith Giffen, Jim Starlin, Larry Lieber, Don Heck","Robert Downey Jr., Chris Evans, Mark Ruffalo, Chris Hemsworth, Scarlett Johansson, Jeremy Renner, Josh Brolin, Don Cheadle, Paul Rudd, Benedict Cumberbatch",2026-10-07T18:14:16.282Z
475557,"Crime, Thriller, Drama","Warner Bros. Pictures, Joint Effort, Village Roadshow Pictures, Bron Studios, DC Films","Canada, United States of America",English,"dream, street gang, society, psychopath, clown, villain, based on comic, murder, psychological thriller, criminal mastermind, mental illness, anarchy, character study, clown makeup, subway train, social realism, supervillain, tv host, 1980s, mother son relationship, origin story, falling into madness, depressing",Todd Phillips,"Todd Phillips, Scott Silver, Bob Kane, Bill Finger, Jerry Robinson","Joaquin Phoenix, Robert De Niro, Zazie Beetz, Frances Conroy, Brett Cullen, Shea Whigham, Bill Camp, Glenn Fleshler, Leigh Gill, Josh Pais",2026-10-07T18:14:16.282Z
271110,"Adventure, Action, Science Fiction",Marvel Studios,United States of America,"Romanian, English, German, Russian","civil war, superhero, based on comic, sequel, aftercreditsstinger, duringcreditsstinger, marvel cinematic universe (mcu), excited","Anthony Russo, Joe Russo","Christopher Markus, Stephen McFeely, Joe Simon, Jack Kirby","Chris Evans, Robert Downey Jr., Scarlett Johansson, Sebastian Stan, Anthony Mackie, Don Cheadle, Jeremy Renner, Chadwick Boseman, Paul Bettany, Elizabeth Olsen",2026-10-07T18:14:16.282Z
284054,"Action, Adventure, Science Fiction",Marvel Studios,United States of America,"English, Korean, Swahili, Xhosa","africa, superhero, based on comic, aftercreditsstinger, duringcreditsstinger, marvel cinematic universe (mcu)",Ryan Coogler,"Ryan Coogler, Joe Robert Cole, Stan Lee, Jack Kirby","Chadwick Boseman, Michael B. Jordan, Lupita Nyong'o, Danai Gurira, Martin Freeman, Daniel Kaluuya, Letitia Wright, Winston Duke, Sterling K. Brown, Angela Bassett",2026-10-07T18:14:16.282Z
284052,"Action, Adventure, Fantasy",Marvel Studios,UNITED STATES OF AMERICA,English,"magic, superhero, training, time, based on comic, sorcerer, doctor, neurosurgeon, wizard, aftercreditsstinger, duringcreditsstinger, marvel cinematic universe (mcu)",Scott Derrickson,N/A,"Benedict Cumberbatch, Chiwetel Ejiofor, Rachel McAdams, Benedict Wong, Mads Mikkelsen, Tilda Swinton, Michael Stuhlbarg, Benjamin Bratt, Scott Adkins, Zara Phythian",2026-10-07T18:14:16.282Z
315635,"Action, Adventure, Science Fiction, Drama","Ma

===== bronze.tb_movies_reviews =====


id,nome,nota,comentario,ingestion_datetime
442113,Mariana Cardoso 277,4.4,null,2026-10-07T18:14:20.518Z
637007,Lucas Reis 602,3.9,null,2026-10-07T18:14:20.518Z
449479,Sérgio Freitas,0.7,Péssimo em todos os sentidos.,2026-10-07T18:14:20.518Z
413036,Gabriela Monteiro 401,7.5,null,2026-10-07T18:14:20.518Z
528480,Leonardo Monteiro,6.3,Assisti até o final mas não me marcou.,2026-10-07T18:14:20.518Z
387727,Maria Alves 707,8.2,"Gostei bastante, recomendo.",2026-10-07T18:14:20.518Z
1032506,Amanda Castro 242,4.7,"Fraco, não recomendo.",2026-10-07T18:14:20.518Z
446554,Sandra Rodrigues 736,6.5,Assisti até o final mas não me marcou.,2026-10-07T18:14:20.518Z
569916,Camila Lima 489,8.2,Muito bom! Vale a pena assistir.,2026-10-07T18:14:20.518Z
864552,Roberto Almeida 555,9.3,"Obra-prima do cinema, simplesmente espetacular.",2026-10-07T18:14:20.518Z


===== bronze.tb_cotacao_dolar =====


cotacaoCompra,dataHoraCotacao,ingestion_datetime
5.1803,2026-09-30 13:11:44.783262,2026-10-07T18:14:24.607Z
5.2073,2026-10-01 13:10:35.4469,2026-10-07T18:14:24.607Z
5.2232,2026-10-02 13:03:16.256632,2026-10-07T18:14:24.607Z
4.9853,2026-10-05 13:07:36.558602,2026-10-07T18:14:24.607Z
4.9692,2026-10-06 13:03:21.267287,2026-10-07T18:14:24.607Z
4.9929,2026-10-07 13:05:23.249063,2026-10-07T18:14:24.607Z
